In [1]:
# Project and symbolic tools
import heyoka as hy
import quivira as qv

# Numerics and visualization
import numpy as np
import matplotlib.pyplot as plt
from matplotlib.animation import FuncAnimation
from IPython.display import HTML

In [2]:
model = qv.bar_joint_model()
model.set_g(9.81)

In [3]:
# First two bars
model.add_bar(np.sqrt(4**2 + 4**2), 1)
model.position_bar(0, 2, 2, np.pi/4)
model.add_bar_at_attitude(2, 2, -np.pi/4, np.sqrt(4**2 + 4**2), 1)
model.add_joint([0, 1], [0.0, 0.0])
# Second two bars
model.add_bar_from_point_pair((4,0),(8,4))
model.add_bar_from_point_pair((4,4),(8,0))
model.add_joint([2, 3], [0.0, 0.0])
# Connect them
model.add_joint([0, 3], [0.5, -0.5])
model.add_joint([1, 2], [0.5, -0.5])
# Make supports
model.add_support(0, -0.5, False, False, 0, 0)
model.add_support(1, -0.5, False, True, 0, 4)

In [4]:
model.build_eom_integrator()

In [5]:
model._check_initial_states_against_constraints()
model._apply_initial_state()

In [ ]:
#model.integrate(400, 2)

In [ ]:
save_gif = False

# propagate the full trajectory
model.ta.time = 0.0
model.ta.state[:] = model.state0
tgrid = np.linspace(0.0, 1.2, 401)
solution = model.ta.propagate_grid(tgrid)[-1]

def bar_endpoints_from_state(state, rod_length):
    x, y, theta = state[0], state[1], state[2]
    u = np.array([np.cos(theta), np.sin(theta)])
    start = np.array([x, y]) - 0.5 * rod_length * u
    end = np.array([x, y]) + 0.5 * rod_length * u
    return start, end

def point_on_bar(q, bar_index, s):
    x, y, theta = q[3 * bar_index : 3 * bar_index + 3]
    L = model.bars[bar_index].length
    return np.array([x, y]) + s * L * np.array([np.cos(theta), np.sin(theta)])

fig, ax = plt.subplots(figsize=(10, 5))
ax.set_aspect("equal")
ax.grid(True)

def init_anim():
    ax.clear()
    ax.set_aspect("equal")
    ax.grid(True)
    ax.set_xlim(-1, 12)
    ax.set_ylim(-1, 5)
    return ()

def update_anim(frame):
    ax.clear()
    ax.set_aspect("equal")
    ax.grid(True)
    ax.set_xlim(-1, 12)
    ax.set_ylim(-1, 5)

    state = solution[frame]
    q = state[:len(model.q)]

    # draw bars without endpoint markers
    for i in range(len(model.bars)):
        x, y, theta = q[3 * i : 3 * i + 3]
        start, end = bar_endpoints_from_state(np.array([x, y, theta]), model.bars[i].length)
        ax.plot([start[0], end[0]], [start[1], end[1]], lw=3, color=f"C{i}", solid_capstyle="round")

    # draw hinge markers (one marker per joint)
    seen_joints = set()
    for joint in model.joints:
        p0 = point_on_bar(q, joint.bar_index[0], joint.s[0])
        key = tuple(np.round(p0, 12))
        if key in seen_joints:
            continue
        seen_joints.add(key)
        ax.plot(p0[0], p0[1], "o", color="black", ms=7, mec="black", mew=1.2)

    # draw support markers
    support_size = 0.5
    for support in model.supports:
        p = point_on_bar(q, support.bar_index, support.s)

        if (not support.dof_in_x) and (not support.dof_in_y):
            # fixed in x and y -> +
            ax.plot(p[0], p[1], "+", color="black", ms=11, mew=2.2)
        elif support.dof_in_x and (not support.dof_in_y):
            # x open: horizontal line
            ax.plot([p[0] - support_size, p[0] + support_size],
                    [p[1], p[1]],
                    color="black", lw=2)
        elif support.dof_in_y and (not support.dof_in_x):
            # y open: vertical line
            ax.plot([p[0], p[0]],
                    [p[1] - support_size, p[1] + support_size],
                    color="black", lw=2)
        else:
            # if both x and y are free, keep it simple
            ax.plot(p[0], p[1], "o", color="black", ms=4)

    return ()

anim = FuncAnimation(
    fig,
    update_anim,
    frames=len(solution),
    interval=20,
    blit=False,
    init_func=init_anim,
)
if save_gif:
    gif_path = "scissor_mechanism.gif"
    anim.save(gif_path, writer="pillow", fps=30, dpi=150)
display(HTML(anim.to_jshtml()))
plt.close(fig)